# **multimoda-rs**: CCTA Module Tutorial

This notebook demonstrates the full CCTA–intravascular fusion pipeline:

1. Read in and label a CCTA geometry from an STL file and centerline CSV files
2. Prepare centerlines, detect branches, and discretize the vessel tree
3. Load an intravascular geometry and fine-align it to the CCTA point cloud
4. Label the anomalous (intramural) region within the CCTA mesh
5. Compute radial scaling factors for the proximal, distal, and aortic regions
6. Morph the CCTA mesh to match the intravascular geometry
7. Remove the intramural region and stitch the CCTA to the intravascular geometry
8. Remesh and smooth the stitched geometry
9. Visualise labeled regions and export section STL files
10. Re-label the final stitched geometry

> **Note**: Example data is loaded automatically from `examples/data/` when run from the repository root.

Load required packages and set the working directory. Performance is typically faster in the console than in a notebook.


In [1]:
import os
from pathlib import Path
import numpy as np
import multimodars as mm

cwd = Path.cwd()
for candidate in [cwd, cwd.parent, cwd.parent.parent]:
    if (candidate / "examples" / "data").exists():
        os.chdir(candidate / "examples" / "data")
        break
    elif (candidate / "data").exists():
        os.chdir(candidate / "data")
        break
print(f"Working directory: {os.getcwd()}")


Working directory: /mnt/d/00_coding/multimoda-rs/examples/data


In [2]:
# Install if needed
%pip --disable-pip-version-check install trimesh plotly scipy pymeshlab | grep -v 'already satisfied'

import trimesh
import plotly.graph_objects as go
import plotly.io as pio
pio.renderers.default = "notebook_connected"

_DARK = dict(
    scene=dict(aspectmode='data', bgcolor='black'),
    margin=dict(r=0, l=0, b=0, t=30),
    legend=dict(yanchor="top", y=0.99, xanchor="left", x=0.01),
    paper_bgcolor="black",
)


def trimesh_to_mesh3d(mesh, color, name, opacity=0.6):
    verts, faces = mesh.vertices, mesh.faces
    return go.Mesh3d(
        x=verts[:,0], y=verts[:,1], z=verts[:,2],
        i=faces[:,0], j=faces[:,1], k=faces[:,2],
        color=color, opacity=opacity, name=name, flatshading=True,
    )


def _to_arr(pts):
    return np.array(pts, dtype=np.float64) if pts else np.empty((0, 3))


def plot_labeled_geometry(results):
    """Visualise initial geometry labeling (aorta / RCA / LCA / removed)."""
    mesh = results["mesh"]
    fig = go.Figure()
    fig.add_trace(go.Mesh3d(
        x=mesh.vertices[:,0], y=mesh.vertices[:,1], z=mesh.vertices[:,2],
        i=mesh.faces[:,0], j=mesh.faces[:,1], k=mesh.faces[:,2],
        opacity=0.1, color='lightgray', name='Mesh', hoverinfo='skip',
    ))
    for key, color, label in [
        ("aorta_points",       "yellow", "Aorta"),
        ("rca_points",         "blue",   "RCA"),
        ("lca_points",         "green",  "LCA"),
        ("rca_removed_points", "red",    "RCA removed (intramural)"),
        ("lca_removed_points", "red",    "LCA removed (intramural)"),
    ]:
        arr = _to_arr(results.get(key, []))
        if len(arr):
            fig.add_trace(go.Scatter3d(
                x=arr[:,0], y=arr[:,1], z=arr[:,2],
                mode='markers', marker=dict(size=2, color=color), name=label,
            ))
    fig.update_layout(**_DARK)
    fig.show()


def plot_anomalous_regions(results):
    """Visualise proximal / anomalous / distal sub-regions."""
    mesh = results["mesh"]
    fig = go.Figure()
    fig.add_trace(go.Mesh3d(
        x=mesh.vertices[:,0], y=mesh.vertices[:,1], z=mesh.vertices[:,2],
        i=mesh.faces[:,0], j=mesh.faces[:,1], k=mesh.faces[:,2],
        opacity=0.1, color='lightgray', name='Mesh', hoverinfo='skip',
    ))
    for key, color, label in [
        ("proximal_points",  "cyan",    "Proximal"),
        ("anomalous_points", "orange",  "Anomalous"),
        ("distal_points",    "magenta", "Distal"),
    ]:
        arr = _to_arr(results.get(key, []))
        if len(arr):
            fig.add_trace(go.Scatter3d(
                x=arr[:,0], y=arr[:,1], z=arr[:,2],
                mode='markers', marker=dict(size=2, color=color), name=label,
            ))
    fig.update_layout(**_DARK)
    fig.show()


def plot_results_key(results):
    """Plotly replacement for mm.plot_results_key — all region labels on one figure."""
    mesh = results["mesh"]
    fig = go.Figure()
    fig.add_trace(go.Mesh3d(
        x=mesh.vertices[:,0], y=mesh.vertices[:,1], z=mesh.vertices[:,2],
        i=mesh.faces[:,0], j=mesh.faces[:,1], k=mesh.faces[:,2],
        opacity=0.15, color='lightgray', name='Mesh', hoverinfo='skip',
    ))
    for key, color, label in [
        ("aorta_points",       "yellow",  "Aorta"),
        ("rca_points",         "blue",    "RCA"),
        ("lca_points",         "green",   "LCA"),
        ("rca_removed_points", "red",     "Intramural wall"),
        ("proximal_points",    "cyan",    "Proximal"),
        ("distal_points",      "magenta", "Distal"),
        ("anomalous_points",   "orange",  "Anomalous"),
    ]:
        arr = _to_arr(results.get(key, []))
        if len(arr):
            fig.add_trace(go.Scatter3d(
                x=arr[:,0], y=arr[:,1], z=arr[:,2],
                mode='markers', marker=dict(size=2, color=color), name=label,
            ))
    fig.update_layout(**_DARK)
    fig.show()


def plot_centerline_branches(rca_cl, lca_cl, results_dict=None):
    """Visualise centerline branch assignments for RCA and LCA.

    Each branch gets its own toggleable legend entry. When *results_dict*
    is provided, labelled surface-mesh points are overlaid so you can verify
    that branch labels transferred correctly to the geometry.

    Colour coding: blues = RCA (dark = main, lighter = side branches);
    reds/oranges = LCA.
    """
    _RCA = ["#1f77b4", "#17becf", "#9467bd", "#2ca02c", "#7f7f7f"]
    _LCA = ["#d62728", "#ff7f0e", "#e377c2", "#bcbd22", "#8c564b"]

    fig = go.Figure()

    def add_cl(cl, colors, vessel):
        from collections import defaultdict
        by_branch = defaultdict(list)
        for p in cl.points:
            by_branch[p.branch_id].append(p.contour_point)
        for bid in sorted(by_branch):
            pts = by_branch[bid]
            label = f"{vessel} main" if bid == 0 else f"{vessel} branch {bid}"
            fig.add_trace(go.Scatter3d(
                x=[p.x for p in pts], y=[p.y for p in pts], z=[p.z for p in pts],
                mode='markers', marker=dict(color=colors[bid % len(colors)], size=3),
                name=label,
            ))

    def add_surf(key, color, label):
        arr = _to_arr(results_dict.get(key, []))
        if len(arr):
            fig.add_trace(go.Scatter3d(
                x=arr[:,0], y=arr[:,1], z=arr[:,2],
                mode='markers', marker=dict(color=color, size=1.5, opacity=0.3),
                name=label,
            ))

    add_cl(rca_cl, _RCA, "RCA")
    add_cl(lca_cl, _LCA, "LCA")

    if results_dict is not None:
        add_surf("rca_points_main", _RCA[0], "RCA main pts")
        i = 1
        while f"rca_points_side_{i}" in results_dict:
            add_surf(f"rca_points_side_{i}", _RCA[i % len(_RCA)], f"RCA side {i} pts")
            i += 1
        add_surf("lca_points_main", _LCA[0], "LCA main pts")
        i = 1
        while f"lca_points_side_{i}" in results_dict:
            add_surf(f"lca_points_side_{i}", _LCA[i % len(_LCA)], f"LCA side {i} pts")
            i += 1

    fig.update_layout(title="Centerline Branch Assignment", **_DARK)
    fig.show()


def plot_vessel_tree(tree, pts_per_contour=24):
    """Visualise a discretized vessel tree.

    Renders contour rings (subsampled to *pts_per_contour* points),
    yellow centroid dots tracing each vessel axis, and orientation
    reference triplets at the ostium and bifurcation sites.

    Colour coding: silver = aorta; steel-blue = RCA main; shades of blue =
    RCA side branches; coral = LCA main; shades of orange = LCA side branches.
    Red × = main reference; orange ▲ = CCW reference; magenta ▼ = CW reference.
    """
    _RCA = ["#1f77b4", "#4fa3e0", "#7ec8e3", "#a8d8ea"]
    _LCA = ["#d62728", "#e07f4f", "#e3a87e", "#eac0a8"]

    fig = go.Figure()

    def ring_xyz(contour):
        pts = contour.points
        m = len(pts)
        if m == 0:
            return [], [], []
        step = max(1, m // pts_per_contour)
        s = pts[::step]
        return ([p.x for p in s] + [s[0].x],
                [p.y for p in s] + [s[0].y],
                [p.z for p in s] + [s[0].z])

    def add_contours(contours, color, name, opacity=0.7):
        rx, ry, rz, cx, cy, cz = [], [], [], [], [], []
        for c in contours:
            xs, ys, zs = ring_xyz(c)
            if not xs:
                continue
            rx += xs + [None]; ry += ys + [None]; rz += zs + [None]
            if c.centroid:
                cx.append(c.centroid[0]); cy.append(c.centroid[1]); cz.append(c.centroid[2])
        if rx:
            fig.add_trace(go.Scatter3d(x=rx, y=ry, z=rz, mode='lines',
                name=name, line=dict(color=color, width=1), opacity=opacity))
        if cx:
            fig.add_trace(go.Scatter3d(x=cx, y=cy, z=cz, mode='markers',
                marker=dict(color='yellow', size=2), showlegend=False,
                name=f"{name} centroids"))

    def add_refs(refs, label):
        mx, my, mz, ccx, ccy, ccz, clx, cly, clz = [], [], [], [], [], [], [], [], []
        for main_ref, cc_ref, clock_ref in refs:
            mx.append(main_ref[0]); my.append(main_ref[1]); mz.append(main_ref[2])
            ccx.append(cc_ref[0]); ccy.append(cc_ref[1]); ccz.append(cc_ref[2])
            clx.append(clock_ref[0]); cly.append(clock_ref[1]); clz.append(clock_ref[2])
        if mx:
            fig.add_trace(go.Scatter3d(x=mx, y=my, z=mz, mode='markers',
                name=f"{label} main ref", marker=dict(color='red', symbol='x', size=5)))
            fig.add_trace(go.Scatter3d(x=ccx, y=ccy, z=ccz, mode='markers',
                name=f"{label} CCW ref", marker=dict(color='orange', symbol='diamond', size=5)))
            fig.add_trace(go.Scatter3d(x=clx, y=cly, z=clz, mode='markers',
                name=f"{label} CW ref", marker=dict(color='magenta', symbol='square', size=5)))

    add_contours(tree.discretized_aorta, "silver", "Aorta", opacity=0.3)
    add_contours(tree.discretized_rca_main, "steelblue", "RCA main")
    for i, branch in enumerate(tree.rca_branches):
        add_contours(branch, _RCA[i % len(_RCA)], f"RCA branch {i+1}")
    add_contours(tree.discretized_lca_main, "coral", "LCA main")
    for i, branch in enumerate(tree.lca_branches):
        add_contours(branch, _LCA[i % len(_LCA)], f"LCA branch {i+1}")
    add_refs(tree.rca_references, "RCA")
    add_refs(tree.lca_references, "LCA")

    fig.update_layout(title="Discretized Vessel Tree", **_DARK)
    fig.show()

def plot_centerline_edges(cl, sharp_angles=None, title="Centerline Edges"):
    """Show centerline branches with sharp-angle positions as red x markers.

    Each branch gets a distinct colour. Plotting only - does not compute
    anything itself, so the same `find_sharp_angles` result can be reused
    for a manual `split_branch`/`merge_branches` fix without recomputing it.

    Parameters
    ----------
    sharp_angles : dict[int, list[int]], optional
        Precomputed `find_sharp_angles` positions per branch_id, e.g.
        ``{0: cl.find_sharp_angles(0, 0.0)}``. Branches with no entry (or
        `None`) are plotted without markers.
    """
    _PALETTE = [
        "#1f77b4", "#ff7f0e", "#2ca02c", "#d62728", "#9467bd",
        "#8c564b", "#e377c2", "#7f7f7f", "#bcbd22", "#17becf",
    ]
    from collections import defaultdict
    by_branch = defaultdict(list)
    for p in cl.points:
        by_branch[p.branch_id].append(p.contour_point)

    sharp_angles = sharp_angles or {}

    fig = go.Figure()
    for bid in sorted(by_branch):
        pts = by_branch[bid]
        color = _PALETTE[bid % len(_PALETTE)]
        label = "main" if bid == 0 else f"branch {bid}"
        fig.add_trace(go.Scatter3d(
            x=[p.x for p in pts], y=[p.y for p in pts], z=[p.z for p in pts],
            mode='lines+markers', name=label,
            line=dict(color=color, width=2),
            marker=dict(color=color, size=3),
        ))
        sharp_pos = sharp_angles.get(bid, [])
        if sharp_pos:
            sharp_pts = [pts[i] for i in sharp_pos if i < len(pts)]
            fig.add_trace(go.Scatter3d(
                x=[p.x for p in sharp_pts], y=[p.y for p in sharp_pts], z=[p.z for p in sharp_pts],
                mode='markers', name=f"{label} sharp angles",
                marker=dict(color='red', size=8, symbol='x'),
            ))
    fig.update_layout(title=title, **_DARK)
    fig.show()

/mnt/d/00_coding/multimoda-rs/.venv/bin/python: No module named pip
Note: you may need to restart the kernel to use updated packages.


## 1. Read in and prepare CCTA geometries and centerlines

The entry point for the CCTA module is `mm.label_geometry`, which reads a triangulated surface mesh
(STL) together with centerline CSV files for the aorta, RCA, and LCA. It returns a labeled `results`
dictionary — it does not return or modify the centerlines you pass in, so orient them yourself first
(below) and reuse those same objects for every subsequent step.

The centerline CSV files must contain three columns (no header): `x`, `y`, `z` in mm.

**Key parameters:**
- `bounding_sphere_radius_mm`: radius of the rolling sphere for the initial vessel labeling pass.
  Larger values capture more distant vertices; smaller values are more conservative.
- `range_mm_takeoff_rca` / `range_mm_takeoff_lca`: arc-length in mm from the proximal end of each
  coronary centerline defining the end of the overlapping/intramural segment, set independently
  per vessel. Expressed as a physical length rather than a point count so it stays correct
  regardless of centerline resampling density.
- `acute_takeoff_rca` / `acute_takeoff_lca`: when `True`, re-assigns incorrectly labeled points overlapping the aortic wall near an acute-angle takeoff.
  Set to `False` for normal coronary anatomy.
- `control_plot`: open an interactive scene to inspect labeling. Useful when tuning the parameters above.

The returned `results` dictionary contains keys `"mesh"`, `"aorta_points"`, `"rca_points"`,
`"lca_points"`, `"rca_removed_points"`, and `"lca_removed_points"`.


In [3]:
rca_cl_raw   = np.genfromtxt("./centerline_rca_short.csv", delimiter=',')
lca_cl_raw   = np.genfromtxt("./centerline_lca.csv",       delimiter=',')
aorta_cl_raw = np.genfromtxt("./centerline_aorta.csv",     delimiter=',')
rca_cl_np   = mm.numpy_to_centerline(rca_cl_raw)
lca_cl_np   = mm.numpy_to_centerline(lca_cl_raw)
aorta_cl_np = mm.numpy_to_centerline(aorta_cl_raw)

rca_cl_np = rca_cl_np.calculate_branches(2.0)
lca_cl_np = lca_cl_np.calculate_branches(2.0)

# Orient once, locally — label_geometry() takes prepared PyCenterline objects
# as-is and no longer returns centerlines, so reuse these same oriented
# objects for every downstream step below.
aorta_cl = aorta_cl_np.orient_by_max_z()
rca_cl_np   = rca_cl_np.orient_to_reference(aorta_cl)
lca_cl_np   = lca_cl_np.orient_to_reference(aorta_cl)

results_np = mm.label_geometry(
    path_ccta_geometry="./NARCO_119.stl",
    centerline_aorta=aorta_cl,
    centerline_rca=rca_cl_np,
    centerline_lca=lca_cl_np,
    bounding_sphere_radius_mm_rca=3.5,
    range_mm_takeoff_rca=40.0,
    range_mm_takeoff_lca=20.0,
    acute_takeoff_rca=True,
    acute_takeoff_lca=False,
    control_plot=False,
)

plot_labeled_geometry(results_np)


Loaded mesh: 25171 vertices, 50338 faces

RCA points found: 4930
LCA points found: 5899
Applying occlusion removal for acute-takeoff RCA...
RCA: relabeled 131 points in intramual course

Removing LCA and RCA island points...
Total faces to exclude: 186
length before: 10698
Excluded 186 faces, removed 131 points (filtered from 4930 to 4799 points)
length after: 10614

Applying final reclassification based on adjacency map...
aorta_points:14438
rca_points:4730
lca_points:5879
rca_removed_points:124
lca_removed_points:0


## 2. Discretize CCTA and map reference points

`rca_cl`/`lca_cl` were loaded from flat CSV files above, so they carry no branch structure yet —
call `calculate_branches` on each, then orient them (`orient_by_max_z` for the aorta,
`orient_to_reference` against it for the coronaries) first (VTP-loaded centerlines skip this, see
the alternative below). `label_branches_pair` then only needs to label the surface-mesh points by
branch — it does not modify `rca_cl`/`lca_cl` in any way. The returned `results` dictionary gains
keys `rca_points_main`, `rca_points_side_1`, …, `lca_points_main`, `lca_points_side_1`, ….

After verifying the branch assignment in the interactive plot, `discretize_vessel_tree` slices each
vessel into evenly-spaced cross-sectional contours and computes orientation reference triplets at
the ostium and every side-branch bifurcation.

**Key parameters:**
- `branch_sigma` (passed to `calculate_branches`): Gaussian smoothing radius (mm) for branch
  detection — increase if the algorithm over-segments noisy centerlines.
- `step_size`: arc-length spacing between consecutive cross-sections (mm).
- `n_points`: number of evenly-spaced points per output contour ring.
- `b_spline`: replace each discretized contour with a closed periodic B-spline fit — useful for
  smoothing jagged contours before computing reference points.  Control strength with
  `bspline_smoothing` (0 = exact; ≈ `n_points` = gentle; ≈ `5 × n_points` = strong).

In [4]:
results_np = mm.label_branches_pair(rca_cl_np, lca_cl_np, results_np)

# Inspect each centerline for sharp angles — red × marks a position that may
# need a split_branch / merge_branches fix.  Tune cos_threshold toward negative
# values (e.g. -0.3) to suppress false positives on gently curved segments.
# Computed once per branch and reused below for the manual correction, instead
# of letting the plot recompute it a second time.
n_branches = len(lca_cl_np.branch_start_indices)
sharp_angles = {
    bid: lca_cl_np.find_sharp_angles(branch_id=bid, cos_threshold=0.0)
    for bid in range(n_branches)
}
plot_centerline_edges(lca_cl_np, sharp_angles=sharp_angles, title="LCA edges")

# Manual corrections (uncomment and adapt as needed):
lca_cl_np = lca_cl_np.split_branch(0, sharp_angles[0][4])
lca_cl_np = lca_cl_np.merge_branches(0, 4)
lca_cl_np = lca_cl_np.orient_by_max_z()
results = mm.label_branches_pair(rca_cl_np, lca_cl_np, results_np)

# Verify final branch assignment after any corrections.
plot_centerline_branches(rca_cl_np, lca_cl_np, results)


Branch labeling for 'rca_points' (branch_ids=[0]):
  rca_points_main: 3759
  rca_points_side: 971
  rca_points_side_1: 514
  rca_points_side_2: 423
  rca_points_side_3: 23

Branch labeling for 'lca_points' (branch_ids=[0]):
  lca_points_main: 5228
  lca_points_side: 651
  lca_points_side_1: 248
  lca_points_side_2: 277
  lca_points_side_3: 114
  lca_points_side_4: 12



Branch labeling for 'rca_points' (branch_ids=[0]):
  rca_points_main: 3759
  rca_points_side: 971
  rca_points_side_1: 514
  rca_points_side_2: 423
  rca_points_side_3: 23

Branch labeling for 'lca_points' (branch_ids=[0]):
  lca_points_main: 3736
  lca_points_side: 2143
  lca_points_side_1: 1606
  lca_points_side_2: 248
  lca_points_side_3: 402
  lca_points_side_4: 12


### Alternative: VTP centerlines from 3D-Slicer / VMTK

If centerlines were exported as `.vtp` files (ASCII VTK PolyData) by 3D-Slicer or VMTK, the
entire preparation workflow simplifies significantly.  `load_centerline` loads the file, then
`prepare_centerline` identifies branches automatically (for the coronaries; the aorta needs
none), removes the run-alongside-main-branch prefix that VTP files attach to every side branch,
resamples, orders, and smooths — all in one call, so `label_branches_pair` only needs to label
the surface points by branch — no manual corrections or explicit
`calculate_branches`/`orient_by_max_z` calls needed.

In [5]:
# Load and clean VTP centerlines. The aorta has no reference to orient
# against, so prepare it first, then pass it as `ref_centerline` for the
# coronaries — this also drives prepare_centerline's branch-detection
# decision (no ref -> aorta -> no side branches to find; a ref -> coronary
# -> extract branches).
aorta_cl = mm.load_centerline("./ao_cl.vtp", name="Aorta")
aorta_cl = mm.prepare_centerline(aorta_cl, spacing_mm=0.5)

rca_cl = mm.load_centerline("./rca_cl.vtp", name="RCA")
rca_cl = mm.prepare_centerline(rca_cl, ref_centerline=aorta_cl, spacing_mm=0.5, rm_start_mm=5.0)

lca_cl = mm.load_centerline("./lca_cl.vtp", name="LCA")
lca_cl = mm.prepare_centerline(lca_cl, ref_centerline=aorta_cl, spacing_mm=0.5, rm_start_mm=5.0)

# Re-run label_geometry with PyCenterline objects instead of file paths
results = mm.label_geometry(
    path_ccta_geometry="./NARCO_119.stl",
    centerline_aorta=aorta_cl,
    centerline_rca=rca_cl,
    centerline_lca=lca_cl,
    bounding_sphere_radius_mm_rca=3.5,
    step_size_mm=0.5,
    range_mm_takeoff_rca=60.0,
    range_mm_takeoff_lca=60.0,
    acute_takeoff_rca=True,
    acute_takeoff_lca=False,
    control_plot=False,
)

# Branches (and their ordering) already come from prepare_centerline above.
results = mm.label_branches_pair(rca_cl, lca_cl, results)

plot_centerline_branches(rca_cl, lca_cl, results)

Loaded Aorta centerline from VTP: 152 points
Loaded RCA centerline from VTP: 2652 points
Loaded LCA centerline from VTP: 2815 points
Loaded mesh: 25171 vertices, 50338 faces

RCA points found: 4904
LCA points found: 5900
Applying occlusion removal for acute-takeoff RCA...
RCA: relabeled 182 points in intramual course
Total faces to exclude: 287

Removing LCA and RCA island points...
length before: 10622
Excluded 287 faces, removed 182 points (filtered from 4904 to 4722 points)
length after: 10535

Applying final reclassification based on adjacency map...
aorta_points:14416
rca_points:4693
lca_points:5880
rca_removed_points:182
lca_removed_points:0

Branch labeling for 'rca_points' (branch_ids=[0]):
  rca_points_main: 3727
  rca_points_side: 966
  rca_points_side_1: 23
  rca_points_side_2: 516
  rca_points_side_3: 423

Branch labeling for 'lca_points' (branch_ids=[0]):
  lca_points_main: 2621
  lca_points_side: 3259
  lca_points_side_1: 2623
  lca_points_side_2: 431
  lca_points_side_3:

In [6]:
tree = mm.discretize_vessel_tree(
    aorta_cl, rca_cl, lca_cl,
    results,
    step_size=1.0,
    n_points=100,
    b_spline=True,          # set True + tune bspline_smoothing to smooth noisy contours
    bspline_smoothing=5.0,
)

plot_vessel_tree(tree)

## 3. Load and align intravascular geometry

Load the intravascular segmentation with `mm.from_file_singlepair` (see the intravascular tutorial
for the full range of loading options and parameter tuning). Then align it to the CCTA centerline
and point cloud with `mm.align_combined`, which first performs a coarse three-point alignment using
anatomical landmarks and then refines the rotation by minimising Hausdorff distances.

**Landmark points** (in mm, CCTA coordinate system):
- Aortic reference — centre of vessel on the aortic side
- Superior reference — proximal end of the intramural segment
- Inferior reference — distal end of the intramural segment

**Key parameters for `align_combined`:**
- `angle_range_deg`: angular search window (±degrees) for Hausdorff refinement.
- `write` / `watertight` / `output_dir`: export OBJ meshes when `write=True`.

In [7]:
rest, (dia_logs, sys_logs) = mm.from_file_singlepair(
    input_path="ivus_rest",
    labels=["aligned_dia", "aligned_sys"],
    output_path="output/rest",
)

ref_points = tree.rca_references[0]

rca_cl_main = rca_cl.get_branch(0)  # alignment needs single-branch CL
aligned, spacing_mm, total_rotation_deg = mm.align_combined(
    rca_cl_main,
    rest,
    ref_points[0],          # aortic reference point
    ref_points[1],          # superior reference point
    ref_points[2],          # inferior reference point
    results['rca_points'],  # CCTA point cloud for Hausdorff refinement
    angle_range_deg=30.0,
    index_range=0,
    write=True,
    watertight=False,
    output_dir="test",
    align_wall_anomalous=True,
)

# Resample the the centerlines with the spacing
rca_cl = rca_cl.resample(spacing_mm)
lca_cl = lca_cl.resample(spacing_mm)
aorta_cl = aorta_cl.resample(spacing_mm)



✅ Successfully built geometry from path
-----------------------------------------
✅ Lumen
❌ Eem
❌ Calcification
❌ Sidebranch
✅ Catheter
-----------------------------------------
Label: aligned_dia
Diastole phase: Yes


✅ Successfully built geometry from path
-----------------------------------------
✅ Lumen
❌ Eem
❌ Calcification
❌ Sidebranch
✅ Catheter
-----------------------------------------
Label: aligned_sys
Diastole phase: No


+--------------------------------------------------------------------+
|        ✅ Finished aligning 'aligned_dia' (anomalous: true)         |
+---------+------------+---------------+-------+-------+-------------+
| Contour | Matched To | Rotation (°) |  Tx   |  Ty   |  Centroid   |
+---------+------------+---------------+-------+-------+-------------+
| 1       | 0          | 7.50          | 0.12  | -0.36 | (3.72,5.25) |
| 2       | 1          | 1.00          | 0.04  | -0.16 | (3.72,5.25) |
| 3       | 2          | 6.00          | -0.28 | 0.03  | (3.72,5.2

eem file not found, skipping: "ivus_rest/eem_diastolic_contours.csv"
sidebranch file not found, skipping: "ivus_rest/branch_diastolic_contours.csv"
process_directory: unknown mapping name 'catheter', skipping
calcification file not found, skipping: "ivus_rest/calcium_diastolic_contours.csv"
sidebranch file not found, skipping: "ivus_rest/branch_systolic_contours.csv"
process_directory: unknown mapping name 'catheter', skipping
eem file not found, skipping: "ivus_rest/eem_systolic_contours.csv"
calcification file not found, skipping: "ivus_rest/calcium_systolic_contours.csv"
resample_centerline_by_contours: centroid_count=14, centroid_mean_spacing=Some(1.2955758552631584), centerline_length=199.6188273558363, spacing=1.295576
resample_centerline_by_contours: produced 155 points


  | (3.72,5.25) |
| 5       | 4          | -24.00        | -0.32 | 0.89  | (3.72,5.25) |
| 6       | 5          | -5.00         | -0.48 | 1.10  | (3.72,5.25) |
| 7       | 6          | -29.50        | -0.94 | 0.82  | (3.72,5.25) |
| 8       | 7          | -18.00        | -1.29 | 0.87  | (3.72,5.25) |
| 9       | 8          | 1.50          | -1.36 | 0.86  | (3.72,5.25) |
| 10      | 9          | -1.00         | -1.68 | 1.27  | (3.72,5.25) |
| 11      | 10         | 47.00         | -1.54 | 1.87  | (3.72,5.25) |
| 12      | 11         | 3.50          | -1.45 | 1.95  | (3.72,5.25) |
| 13      | 12         | 1.00          | -1.51 | 2.08  | (3.72,5.25) |
| 14      | 13         | 30.50         | -0.96 | 2.12  | (3.72,5.25) |
| 15      | 14         | -7.00         | -1.11 | 1.93  | (3.72,5.25) |
| 16      | 15         | 19.50         | -0.68 | 2.47  | (3.72,5.25) |
| 17      | 16         | 3.50          | -0.50 | 2.35  | (3.72,5.25) |
| 18      | 17         | -1.00         | -0.58 | 2.24  | (3

## 4. Label the anomalous region

`mm.label_anomalous_region` subdivides the RCA points into three sub-regions — proximal, anomalous
(intramural), and distal — based on spatial overlap between the aligned intravascular frames and the
CCTA mesh. The `results` dictionary is extended with `"proximal_points"`, `"anomalous_points"`,
and `"distal_points"`.

Set `debug_plot=True` to open an interactive scene that shows the sub-region boundaries — useful
when a boundary appears misplaced.

In [8]:
results = mm.label_anomalous_region(
    centerline=rca_cl,
    frames=aligned.geom_a.frames,
    results=results,
    results_key='rca_points',
    debug_plot=False,
)

plot_anomalous_regions(results)


  18 island point(s) reassigned from 'rca_points' sub-regions to aorta_points

Applying anomalous labeling based on aligned intravascular frames...
proximal_points: 34
distal_points: 4223
anomalous_points: 418


## 5. Compute scaling factors

Before morphing, the optimal radial scaling factor for each region is computed independently.
Each function searches for the scale that minimises distance between the CCTA mesh and the
corresponding portion of the aligned intravascular geometry. All return values are signed floats
in mm (+ expands, − contracts).

| Function | Region |
|---|---|
| `find_distal_and_proximal_scaling` | proximal and distal segments |
| `find_aorta_scaling` | aortic vertices, minimising distance to outer intravascular wall |
| `find_aortic_wall_scaling` | aortic *wall* vertices, targeting the intramural→free-segment transition |

> **Note:** `find_aortic_wall_scaling` raises `ValueError` if no frame with elliptic ratio < 1.3
> is found (nearly circular geometry). Omit this step in that case.

In [9]:
prox_scaling, distal_scaling = mm.find_distal_and_proximal_scaling(
    frames=aligned.geom_a.frames,
    centerline=rca_cl,
    results=results,
)

aortic_scaling = mm.find_aorta_scaling(
    frames=aligned.geom_a.frames,
    cl_aorta=aorta_cl,
    results=results,
)

aortic_wall_scaling = mm.find_aortic_wall_scaling(
    frames=aligned.geom_a.frames,
    cl_aorta=aorta_cl,
    results=results,
)

print(f"Proximal scaling:    {prox_scaling:.3f} mm")
print(f"Distal scaling:      {distal_scaling:.3f} mm")
print(f"Aortic scaling:      {aortic_scaling:.3f} mm")
print(f"Aortic wall scaling: {aortic_wall_scaling:.3f} mm")



Finding best proximal/distal radial scaling factors...
Proximal scaling: -0.5 mm
Distal scaling: 0.3 mm

Finding best aortic radial scaling factor...
Aortic scaling: -0.3 mm

Finding best aortic wall radial scaling factor...
elliptic ratio <1.3 for frame index 7
Aortic wall scaling: 1.31 mm
Proximal scaling:    -0.500 mm
Distal scaling:      0.300 mm
Aortic scaling:      -0.300 mm
Aortic wall scaling: 1.314 mm


## 6. Morph CCTA to intravascular geometry

`mm.scale_region_centerline_morphing` moves mesh vertices radially along the local centerline normal
so that the region diameter changes by `diameter_adjustment_mm`. After each call,
`mm.sync_results_to_mesh` updates all coordinate lists in `results` to reflect the new vertex
positions. **Always sync before the next morphing step.**

The three regions are morphed in order: distal → aortic → proximal.

In [10]:
# 1. Scale the distal segment along the RCA centerline
scaled_distal = mm.scale_region_centerline_morphing(
    mesh=results['mesh'],
    region_points=results['distal_points'],
    centerline=rca_cl,
    diameter_adjustment_mm=distal_scaling,
)
results = mm.sync_results_to_mesh(results, results['mesh'], scaled_distal)

# 2. Scale the aortic region (aorta + intramural wall) along the aortic centerline
scaled_distal_aortic = mm.scale_region_centerline_morphing(
    mesh=results['mesh'],
    region_points=results['aorta_points'] + results['rca_removed_points'],
    centerline=aorta_cl,
    diameter_adjustment_mm=aortic_scaling,
)
results = mm.sync_results_to_mesh(results, results['mesh'], scaled_distal_aortic)

# 3. Scale the proximal segment along the RCA centerline
scaled_proximal = mm.scale_region_centerline_morphing(
    mesh=results['mesh'],
    region_points=results['proximal_points'],
    centerline=rca_cl,
    diameter_adjustment_mm=prox_scaling,
)
results = mm.sync_results_to_mesh(results, results['mesh'], scaled_proximal)

# Overlay scaled CCTA with the aligned intravascular geometry
anomaly_mesh      = trimesh.load("test/lumen_000_None.obj")
anomaly_wall_mesh = trimesh.load("test/wall_000_None.obj")
fig = go.Figure(data=[
    trimesh_to_mesh3d(results['mesh'],   "darkred",   "CCTA scaled",         opacity=0.5),
    trimesh_to_mesh3d(anomaly_mesh,      "royalblue", "Intravascular lumen", opacity=0.7),
    trimesh_to_mesh3d(anomaly_wall_mesh, "lightblue", "Intravascular wall",  opacity=0.3),
])
fig.update_layout(scene=dict(aspectmode="data"), margin=dict(l=0, r=0, t=30, b=0))
fig.show()



Scaling 4223 vertices around Centerline(len=223, spacing=1.29 mm, branches=4)
Diameter adjustment: 0.3 mm

Scaling 14616 vertices around Centerline(len=45, spacing=1.28 mm, branches=1)
Diameter adjustment: -0.3 mm

Scaling 34 vertices around Centerline(len=223, spacing=1.29 mm, branches=4)
Diameter adjustment: -0.5 mm


## 7. Remove intramural region and stitch geometries

`mm.remove_labeled_points_from_mesh` deletes the anomalous and proximal vertices. Cutting a segment
out of the middle of the vessel opens **two** boundary rings — one at each cut face — so pass
`target_boundaries=2`. The `results` dictionary gains:

- `"boundary_points_1"`, `"boundary_points_2"`, … — one ordered ring each, in walk order.
- `"boundary_points"` — all boundary vertices concatenated, for callers that ignore the split.

The rim is cleaned in the same step: vertices that cannot form a clean ring (isolated stragglers,
dangling hairs, pinch junctions where two holes meet, sharp spikes) are deleted from the mesh, not
just skipped in the stored ring, so the stored ring really traces the mesh's open edge. Any culled
vertices are reported.

> If the trim yields more rings than `target_boundaries`, the surplus is merged by nearest endpoints
> and a warning is printed. That join bridges a gap which is *not* a mesh edge, so treat the warning
> as a prompt to raise `target_boundaries` rather than as cosmetic noise.

Inspect the result with `mm.plot_boundary_edges(updated_results)`, which draws each ring's edges and
colours its vertices red→blue by walk order. It reports every ring the mesh actually has.

`mm.stitch_ccta_to_intravascular` then triangulates one patch per seam. Each ring is assigned to an
intravascular end **as a whole** — by whichever ring-to-end pairing is closest overall — so a single
ring is never torn across both seams. Each ring is then projected onto its own best-fit plane,
smoothed, and respaced evenly — except an ostial proximal ring with `prox_start_mode="highest_z"`,
which is conditioned as two halves instead (see *Two-half ostium* below) — and both are densified to
the stitching resolution by inserting points along their edges; each subdivided edge's face is
retriangulated onto its opposite vertex, so the new points are real mesh vertices rather than
T-junctions.

**`prox_start_mode` / `dist_start_mode`:**
- `"nearest_iv"` (default) — rotate to the boundary vertex closest to intravascular point 0.
- `"highest_z"` — rotate to the boundary vertex with the largest z-coordinate; prefer for straight
  intramural segments where the pullback axis is nearly aligned with the image z-axis. On an ostial
  proximal ring it also switches to the two-half ostium conditioning below.

**`boundary_point_ratio`** (default 1.0) — how many points the CCTA ring is densified to, as a
fraction of `n_points_iv_cont`. At 1.0 both rings have equal counts and the patch is a clean quad
strip; lower values (e.g. 0.67) leave the CCTA rim coarser. The patch is hole-free either way.

> Stitching needs two rings. With fewer it raises `ValueError` naming `target_boundaries=2`, rather
> than failing deep inside the patch construction.


### Anomalous ostium corrections (`clamp_overshoot`)

For anomalous coronary arteries the intramural course runs roughly **perpendicular** to the aortic
wall. This means the plane of the intravascular (IV) ring at the ostium is nearly at 90° to the
plane of the aortic boundary ring. Without correction, some aortic boundary vertices end up on the
wrong side of the ostium plane (i.e. inside the coronary lumen), creating a jagged seam.

With the default `prox_start_mode="nearest_iv"`, the following corrections are applied
automatically when the angle between the two planes exceeds 45° (for `"highest_z"` see *Two-half
ostium* below):

1. **Whole-plane shift** — if the boundary ring's own plane cuts through the IV ostial frame, the
   entire plane is slid toward the aorta until it clears every frame point by `clamp_overshoot` mm,
   and the ring is re-projected onto the shifted plane. The "toward the aorta" direction comes from
   the labelled `"aorta_points"` centroid — the vessel axis is *not* a usable substitute, because an
   intramural coronary runs inside the aortic wall, so the aortic lumen lies roughly perpendicular
   to that axis. A console message reports the distance moved and which reference was used.
2. **Clamp** — any boundary vertex still on the intravascular side of the ostium plane is projected
   back onto that plane.
3. **Minimum gap** (`clamp_overshoot`, default 0.5 mm) — every boundary vertex (including freshly
   clamped ones) is pushed at least `clamp_overshoot` mm away from the ostium plane on the aortic
   side. This prevents the stitching patch from meeting the aortic wall at a razor-sharp angle at
   the ostium edge.
4. **Layer propagation** — the two rings of aortic mesh vertices adjacent to the boundary ring are
   shifted radially *outward* from the coronary axis (within the ostium plane), by 0.1 mm and
   0.2 mm respectively. This prevents those second-layer vertices from sitting closer to the
   coronary axis than the boundary ring itself, which would otherwise create a visible ridge just
   outside the seam.

`clamp_overshoot` can be tuned per case. Set it to `0` to disable steps 3 and 4 (pure clamping
only).

> If the console reports `direction from vessel axis (no aorta_points)`, the aortic label was empty
> at stitch time and step 1 fell back to the unreliable heuristic. `aorta_points` is filtered by
> every removal step, so check that it survived.

#### Two-half ostium (`prox_start_mode="highest_z"`)

A steep, intramural take-off can leave the aorta-facing half of the ring almost perpendicular to its
coronary-facing half, so no single plane or circle fits it. With `prox_start_mode="highest_z"` (and
the default `proximal_is_ostium=True`) — as in the cell below — the proximal ring is therefore
conditioned as two halves instead of by the corrections above:

1. **Split** — the ring is split into the aorta-facing *Half A* and the coronary-facing *Half B*,
   using the ostial frame's own `aortic` point flags.
2. **Half A** is replaced by the ostial frame's aorta-side lumen contour, scaled up so its mean
   radius grows by the frame's `aortic_thickness` (`clamp_overshoot` when it has none). None of the
   CCTA geometry there survives.
3. **Half B** keeps the CCTA's own shape; a light spline only irons out outliers.
4. **Clamp and minimum gap** — as in steps 2–3 above, when the ring and the IV plane diverge by
   ≥ 45°.
5. **Seam arcs** — at both seams where the halves meet, `seam_points_a` Half A points and
   `seam_points_b` Half B points (default 2 / 4) are replaced by a smooth arc that follows each
   half's own direction. Nothing else moves, so Half A's mid-section keeps its exact wall-thickness
   offset.
6. **Fade-in** — the ring's displacement is faded into the surrounding aortic mesh over a few
   layers, so the mesh behind the rim follows it instead of folding; the layer propagation of
   step 4 above then runs as well.

**`fillet_bulge`** (default 0.0) then rounds the strip between Half A and the intravascular ring into
an arc that bulges away from the intravascular geometry — towards the aorta — instead of leaving a
sharp edge. The arc's height is `fillet_bulge` times each strut's length, built from `fillet_layers`
(default 2) intermediate rings. It fades out along the seam arcs, so Half B and the distal seam stay
direct strips; without the two-half ostium a warning is printed and the direct strip is used.

> The seam counts are points on the CCTA ring as cut from the mesh — often only 20–40 at the
> ostium — not on the ring after densification. Raise `seam_points_b` if Half B's end curls in
> towards the lumen and leaves a hook at a seam; a large `seam_points_a` shortens the part of Half A
> that keeps the exact offset. Counts a half cannot give are reduced with a warning.

> **Known limitation:** at the tips of a slit-like ostium the aortic wall can still touch the first
> millimetres of the intravascular tube, leaving a few self-intersecting faces that
> `fix_and_remesh_stitched_mesh` does not remove. Check the ostium before running simulations.


In [ ]:
updated_results = mm.remove_labeled_points_from_mesh(
    results,
    ["anomalous_points", "proximal_points"],
    target_boundaries=2,
)

stitched = mm.stitch_ccta_to_intravascular(
    aligned.geom_a,
    updated_results['mesh'],
    updated_results,
    prox_start_mode="highest_z",
    clamp_overshoot=0.5,
)
stitched['mesh'].export("prefixed_mesh.stl")
print("Raw stitched mesh exported → prefixed_mesh.stl")


Applying removal of '['anomalous_points', 'proximal_points']'
Removed 452
Created 47 boundary points in 2 ring(s): [29, 18]
Raw stitched mesh exported → prefixed_mesh.stl


In [20]:
# Visualise both stitching seams: each CCTA boundary ring plus the IV lumen ring
# it was stitched to.  Points are coloured red->blue by index, so a healthy seam
# has the two rings starting at the same place and running the same way round.
# Circles = CCTA boundary, diamonds = IV lumen.
#
# The index colouring only matches what the stitcher used if the corresponding
# *_start_mode is "highest_z" (that is what triggers sort_frame_points below).
iv_viz = aligned.geom_a.downsample(100).sort_frame_points()

seams = [
    ("Proximal", stitched['prox_boundary_points'], iv_viz.frames[0].lumen.points),
    ("Distal",   stitched['dist_boundary_points'], iv_viz.frames[-1].lumen.points),
]

fig = go.Figure()
fig.add_trace(trimesh_to_mesh3d(stitched['mesh'], "lightgray", "Stitched mesh", opacity=0.2))

for label, boundary_ring, iv_ring in seams:
    bnd = np.array(boundary_ring, dtype=np.float64)
    iv  = np.array([[p.x, p.y, p.z] for p in iv_ring], dtype=np.float64)
    print(f"{label:9s} seam: CCTA ring {len(bnd):4d} pts | IV ring {len(iv):4d} pts")

    fig.add_trace(go.Scatter3d(
        x=bnd[:,0], y=bnd[:,1], z=bnd[:,2],
        mode='markers',
        marker=dict(size=3, symbol='circle',
                    color=list(range(len(bnd))), colorscale='RdBu', showscale=False),
        name=f'{label} CCTA boundary ring',
    ))
    fig.add_trace(go.Scatter3d(
        x=iv[:,0], y=iv[:,1], z=iv[:,2],
        mode='markers',
        marker=dict(size=3, symbol='circle',
                    color=list(range(len(iv))), colorscale='RdBu', showscale=False),
        name=f'{label} IV lumen ring',
    ))

fig.update_layout(scene=dict(aspectmode='data'), margin=dict(l=0, r=0, t=30, b=0))
fig.show()


Proximal  seam: CCTA ring  100 pts | IV ring  100 pts
Distal    seam: CCTA ring  100 pts | IV ring  100 pts


## 8. Remesh and smooth

`mm.fix_and_remesh_stitched_mesh` applies a three-step repair pipeline:
non-manifold repair → hole filling → isotropic remesh (via `pymeshlab`).
Taubin smoothing then reduces surface noise while preserving overall shape.

> **Requires:** `pip install 'multimodars[meshlab]'`

**Key parameters:**
- `target_edge_length_mm`: desired edge length after remeshing (`None` uses the 25th-percentile edge
  length of the input mesh).
- `verbose`: print per-step vertex/face counts and watertightness.

In [13]:
remeshed = stitched.copy()
remeshed['mesh'] = mm.fix_and_remesh_stitched_mesh(
    stitched['mesh'],
    target_edge_length_mm=0.5,
    verbose=True,
)
print(f"Watertight? {remeshed['mesh'].is_watertight}")

trimesh.smoothing.filter_taubin(remeshed['mesh'], lamb=0.6)
remeshed['mesh'].export("fixed_mesh.stl")
print("Remeshed and smoothed geometry exported → fixed_mesh.stl")


[input                              ] verts= 26,271  faces= 52,538  watertight=True
  non-manifold edges/vertices repaired
  holes closed
[after hole fill                    ] verts= 26,271  faces= 52,538  watertight=True
  target edge=0.5000 mm  (0.2585% of bbox diag=193.44 mm)
[after remesh                       ] verts= 57,710  faces=115,416  watertight=True
Watertight? True
Remeshed and smoothed geometry exported → fixed_mesh.stl


## 9. Visualise and export sections

Inspect all labeled regions of the stitched result, then export individual anatomical sections as
STL files with `mm.export_section_stl`.

| Colour | Region |
|--------|--------|
| Yellow | Aorta |
| Blue | RCA |
| Green | LCA |
| Red | Intramural wall (removed) |
| Cyan | Proximal |
| Magenta | Distal |
| Orange | Anomalous |

In [14]:
mesh = stitched['mesh']
verts, faces = mesh.vertices, mesh.faces

intensity = mesh.vertex_normals[:, 2]

fig = go.Figure(data=[go.Mesh3d(
    x=verts[:,0], y=verts[:,1], z=verts[:,2],
    i=faces[:,0], j=faces[:,1], k=faces[:,2],
    intensity=intensity,
    colorscale="RdBu",
    opacity=1.0,
    flatshading=False,
    name="Stitched geometry",
)])
fig.update_layout(scene=dict(aspectmode="data"), margin=dict(l=0, r=0, t=30, b=0))
fig.show()

In [15]:
mm.export_section_stl(stitched, "all")
mm.export_section_stl(stitched, "aorta")
mm.export_section_stl(stitched, "rca")
mm.export_section_stl(stitched, "lca")
print("Exported: all.stl  aorta.stl  rca.stl  lca.stl")


Exported: all.stl  aorta.stl  rca.stl  lca.stl


## 10. Re-label the final geometry

After remeshing and smoothing, vertex coordinates have changed and the stored point lists are no
longer valid. Re-running `mm.label_geometry` on the exported fixed mesh produces a fresh, consistent
labeling for downstream biomechanical simulation or further analysis.

In [ ]:
results_final = mm.label_geometry(
    path_ccta_geometry="fixed_mesh.stl",
    # Reuse the same oriented centerlines from above — the mesh's vertex
    # positions changed after remeshing/smoothing but the anatomical
    # centerlines did not, and label_geometry takes prepared PyCenterline
    # objects directly rather than loading paths itself.
    centerline_aorta=aorta_cl,
    centerline_rca=rca_cl,
    centerline_lca=lca_cl,
    bounding_sphere_radius_mm_rca=4.0,
    range_mm_takeoff_rca=60.0,
    range_mm_takeoff_lca=60.0,
    acute_takeoff_rca=True,
    acute_takeoff_lca=False,
    control_plot=False,
)

plot_labeled_geometry(results_final)

mm.export_section_stl(results_final, "all")
mm.export_section_stl(results_final, "aorta")
mm.export_section_stl(results_final, "lca")
mm.export_section_stl(results_final, "rca")
print("Final labeled sections exported.")


Loaded mesh: 57710 vertices, 115416 faces

RCA points found: 13698
LCA points found: 14117
Applying occlusion removal for acute-takeoff RCA...
Total faces to exclude: 364
RCA: relabeled 647 points in intramual course

Removing LCA and RCA island points...
length before: 27168
Excluded 364 faces, removed 647 points (filtered from 13698 to 13051 points)
length after: 26848

Applying final reclassification based on adjacency map...
aorta_points:30207
rca_points:12811
lca_points:14080
rca_removed_points:612
lca_removed_points:0


Final labeled sections exported.
